## Functional Gene Ontology (GO) analysis using the ViSEAGO package

In [1]:
#https://bioconductor.org/packages/devel/bioc/vignettes/ViSEAGO/inst/doc/ViSEAGO.html#installation

##Install ViSEAGO package from Bioconductor
#BiocManager::install("ViSEAGO", force = TRUE)
#BiocManager::install("S4Vectors", force = TRUE)

In [2]:
suppressPackageStartupMessages({
    library(org.EcK12.eg.db)
    library(ViSEAGO)
    library(ggplot2)
    library(dplyr)
    library(plotly)
})

Warning message:
“replacing previous import ‘data.table::set’ by ‘dendextend::set’ when loading ‘ViSEAGO’”


In [3]:
run_analysis <- function(condition) {
  ruta <- "./infiles/genes_categories"
  file <- paste0("genesfitness_", condition, ".csv")
  ruta_archivo <- file.path(ruta, file)
  
  # background genes y selection
  background <- keys(org.EcK12.eg.db, keytype ='ENTREZID')
  entrezids <- AnnotationDbi::select(org.EcK12.eg.db, keys=background, columns = c("ENTREZID","SYMBOL"))
  data_file <- read.csv(ruta_archivo)
  
  # Filter data by category
  data_es <- data_file  %>% filter(Categ == "Essen") %>% select(gene)
  data_nofit = read.csv('../Ntbooks_finales/infiles/essential_287gdeNofit_otherConds.csv')
  data_es = rbind(data_es, data_nofit)

  data_imp <- data_file  %>% filter(Categ == "Important") %>% select(gene)
  data_noef <- data_file  %>% filter(Categ == "No_effect" | Categ == "No_effect2") %>% select(gene)
  data_enhance <- data_file  %>% filter(Categ == "Enhancing") %>% select(gene)
  data_es <- merge(data_es, entrezids, by.x = 'gene', by.y = 'SYMBOL', all.x = TRUE)
  data_imp <- merge(data_imp, entrezids, by.x = 'gene', by.y = 'SYMBOL', all.x = TRUE)
  data_noef <- merge(data_noef, entrezids, by.x = 'gene', by.y = 'SYMBOL', all.x = TRUE)
  data_enhance <- merge(data_enhance, entrezids, by.x = 'gene', by.y = 'SYMBOL', all.x = TRUE)
  
  # Select Entrez IDs
  entrezid_es <- data_es$ENTREZID
  entrezid_imp <- data_imp$ENTREZID
  entrezid_no_effect <- data_noef$ENTREZID
  entrezid_enh <- data_enhance$ENTREZID
  
  return(list(
    entrezid_es,
    entrezid_imp,
    entrezid_no_effect,
    entrezid_enh
  ))
}

In [4]:
# GO annotation
Bioconductor <- ViSEAGO::Bioconductor2GO()
myGENE2GO <- ViSEAGO::annotate("org.EcK12.eg.db", Bioconductor)
background <- keys(org.EcK12.eg.db, keytype ='ENTREZID')

'select()' returned 1:many mapping between keys and columns



In [5]:
conditions <- c('Glucose','LB','Glucosamine','Glycerol','Xylose','Mannose','Galactose','Fructose','Acetate',
                'Pyruvate','Succinate')

for (c in conditions) {
    resultados <- paste0("resultados_", c)
    print(resultados)
    resultados <- run_analysis(c)
    
    #GO enrichment tests -TopGO for BP
    BP_essential <- ViSEAGO::create_topGOdata(
        geneSel = resultados[[1]],
        allGenes = background,
        gene2GO = myGENE2GO, 
        ont = "BP", 
        nodeSize = 20
      )
    BP_important <- ViSEAGO::create_topGOdata(
        geneSel = resultados[[2]], 
        allGenes = background,
        gene2GO = myGENE2GO, 
        ont = "BP", 
        nodeSize = 20
      ) 
    BP_no_effect <- ViSEAGO::create_topGOdata(
        geneSel = resultados[[3]], 
        allGenes = background,
        gene2GO = myGENE2GO, 
        ont = "BP", 
        nodeSize = 20
      )
    BP_enhance <- ViSEAGO::create_topGOdata(
        geneSel = resultados[[4]], 
        allGenes = background,
        gene2GO = myGENE2GO, 
        ont = "BP", 
        nodeSize = 20
      )
    #perform TopGO test using elim algorithm 
    elim_BP_essential <- topGO::runTest(
      BP_essential, algorithm = "elim",
      statistic = "fisher", cutOff = 0.01
      )  
    elim_BP_important <- topGO::runTest(
      BP_important, algorithm = "elim",
      statistic = "fisher", cutOff = 0.01
      ) 
    elim_BP_no_effect <- topGO::runTest(
      BP_no_effect, algorithm = "elim",
      statistic = "fisher", cutOff = 0.01
      )
    elim_BP_enhance <- topGO::runTest(
      BP_enhance, algorithm = "elim",
      statistic = "fisher", cutOff = 0.01
      ) 
    
    ##4. merge results from topGO
    BP_sResults <- ViSEAGO::merge_enrich_terms(
        cutoff = 0.01, Input = list(
          Essential = c("BP_essential", "elim_BP_essential"),
          Important = c("BP_important", "elim_BP_important"),
          No_effect = c("BP_no_effect", "elim_BP_no_effect"),
          Fitness_enhancing = c("BP_enhance", "elim_BP_enhance")
        )
    )
  
    # print the merged table in a file
    ViSEAGO::show_table(
        BP_sResults, 
        name_file <- paste0("./Viseago_Res/BP_Results_", c, ".xls")
    )
}

[1] "resultados_Glucose"


'select()' returned 1:1 mapping between keys and columns

Loading required package: topGO

Loading required package: graph

Loading required package: GO.db

Loading required package: SparseM


Attaching package: ‘SparseM’


The following object is masked from ‘package:base’:

    backsolve



groupGOTerms: 	GOBPTerm, GOMFTerm, GOCCTerm environments built.


Attaching package: ‘topGO’


The following object is masked from ‘package:IRanges’:

    members



Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )

geneSel contain genes redondancy.
duplicate elements were removed.


Building most specific GOs .....

	( 180

[1] "resultados_LB"


'select()' returned 1:1 mapping between keys and columns


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )

geneSel contain genes redondancy.
duplicate elements were removed.


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )


			 -- El

[1] "resultados_Glucosamine"


...

'select()' returned 1:1 mapping between keys and columns


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )

geneSel contain genes redondancy.
duplicate elements were removed.


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )

geneSel contain genes redondancy.
duplicate elements were removed.


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...

[1] "resultados_Pyruvate"


'select()' returned 1:1 mapping between keys and columns


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )

geneSel contain genes redondancy.
duplicate elements were removed.


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )


			 -- El

[1] "resultados_Succinate"


'select()' returned 1:1 mapping between keys and columns


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )

geneSel contain genes redondancy.
duplicate elements were removed.


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )

geneSel contain genes redondancy.
duplicate elements were removed.


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...............

	( 3324 genes annotated to the GO terms. )


Building most specific GOs .....

	( 1803 GO terms found. )


Build GO DAG topology ..........

	( 3098 GO terms and 6354 relations. )


Annotating nodes ...

## Up to this point, the enrichment results are obtained and saved in the folder 
## ./Viseago_Res.

In [6]:
#4.2  Graphs of GO enrichment tests
ViSEAGO::GOcount(BP_sResults)    ## AQUI HACE LA GRAF DE BARRAS
p <- ViSEAGO::GOcount(BP_sResults) 

HTML widgets cannot be represented in plain text (need html)

In [7]:
library(plotly)
embed_notebook(p)